# 01 — Exploratory Data Analysis

**Where do We Lose?** — Process Bottleneck Detection & Optimization System

This notebook explores the loan application process at the *application*
level: volume, processing time, and SLA performance. All computations use
the reusable functions in `src/process_mining/`; this notebook is
visualization and interpretation only, per the project's code-quality rule
(no business logic living only in a notebook).

Every chart below is followed by a short **Business Interpretation** —
we're not just describing distributions, we're explaining what they mean
operationally.

In [1]:
import sys
sys.path.insert(0, "..")

import pandas as pd
import plotly.express as px
import plotly.graph_objects as go

from src.process_mining.event_log import load_process_instances
from src.process_mining.process_metrics import compute_cycle_time_stats, compute_sla_breach_rate

pd.set_option("display.max_columns", None)
px.defaults.template = "plotly_white"

pi = load_process_instances("../data/raw/process_instances.csv")
print(f"{len(pi):,} process instances loaded")
pi.head()

50,000 process instances loaded


,process_id,application_date,customer_segment,application_type,loan_amount,risk_score,complexity_score,channel,region,priority,missing_documents,final_status,rejection_stage,total_reworks,total_processing_time_hours,sla_target_hours,sla_breached
0,PROC_0000000,2024-08-08 12:20:23.529538016,SME,Business Loan,123617.92,63.4,71.6,Broker,Central,Standard,0,Completed,NaN,1,285.51,282.9,1
1,PROC_0000001,2024-08-01 15:56:38.961469243,Retail,Auto Loan,15989.80,8.6,52.5,Broker,Central,Standard,1,Completed,NaN,0,161.84,186.0,0
2,PROC_0000002,2025-04-18 19:19:00.930078570,Premium,Auto Loan,23537.70,29.1,52.3,Online,East,High,1,Rejected,Risk Review,1,160.11,158.1,1
3,PROC_0000003,2024-11-11 08:53:17.060586129,SME,Personal Loan,5336.29,27.5,44.9,Branch,West,Standard,0,Completed,NaN,0,97.39,156.0,0
4,PROC_0000004,2025-02-19 12:04:08.992579008,Retail,Auto Loan,14455.41,30.9,36.1,Mobile App,West,Standard,0,Completed,NaN,0,147.76,186.0,0


## Process Volume

In [2]:
daily_volume = pi.set_index("application_date").resample("D").size().rename("applications")
fig = px.line(daily_volume, title="Applications Submitted per Day")
fig.update_layout(yaxis_title="applications", xaxis_title="date")
fig.show()

**Business Interpretation.** Volume follows a clear weekly rhythm — high on
Mondays and Fridays, minimal on weekends — because the arrival schedule
mirrors real customer behavior (branch/online submissions cluster on
business days). This weekly cadence is exactly what creates the Monday
queueing effect explored in the process-mining notebook: capacity is fixed,
but demand spikes predictably.

In [3]:
by_channel = pi["channel"].value_counts().reset_index()
by_channel.columns = ["channel", "applications"]
fig = px.bar(by_channel.sort_values("applications"), x="applications", y="channel",
             orientation="h", title="Applications by Channel", text="applications")
fig.show()

**Business Interpretation.** Branch and Online are the two largest channels,
followed by Mobile App and Broker. Channel matters operationally because it
correlates with data quality — digital, self-service channels have a higher
rate of missing documents (see below), which is one of the strongest
predictors of rework and delay.

In [4]:
by_region = pi["region"].value_counts().reset_index()
by_region.columns = ["region", "applications"]
fig = px.bar(by_region.sort_values("applications"), x="applications", y="region",
             orientation="h", title="Applications by Region", text="applications")
fig.show()

**Business Interpretation.** Demand is fairly evenly spread across regions,
with Central and North the largest. There is no single region driving
volume, so any capacity fix (more staff at a bottleneck stage) benefits the
whole network rather than a specific geography.

In [5]:
by_segment = pi["customer_segment"].value_counts().reset_index()
by_segment.columns = ["customer_segment", "applications"]
fig = px.pie(by_segment, names="customer_segment", values="applications",
             title="Applications by Customer Segment", hole=0.4)
fig.show()

**Business Interpretation.** Retail dominates volume (as expected for a
consumer lender), with SME a distant second. Premium and Corporate are a
small share of volume but — as we'll see in the SLA section — carry tighter
SLA targets and expedited handling, so they deserve disproportionate
operational attention relative to their headcount.

## Processing Time

In [6]:
stats = compute_cycle_time_stats(pi)
display(stats.round(1))

fig = px.histogram(pi, x="total_processing_time_hours", nbins=80,
                    title="Distribution of Total Processing Time (hours)")
for col, label in [("mean_hours", "mean"), ("median_hours", "median"), ("p90_hours", "P90")]:
    fig.add_vline(x=stats.loc[0, col], line_dash="dash",
                   annotation_text=label, annotation_position="top")
fig.show()

,n,mean_hours,median_hours,p90_hours,p95_hours
0,50000,165.3,161.9,254.2,281.8


**Business Interpretation.** The distribution is right-skewed, as expected
for a queue-driven process: most applications move through in well under a
week, but a long tail — cases that hit high-utilization days, missing
documents, or rework loops — stretches out to several weeks. The gap
between the median and P90 is the practical size of the "bottleneck tax":
it's the extra time a meaningfully large minority of customers actually
experience.

In [7]:
fig = px.box(pi, x="application_type", y="total_processing_time_hours", color="application_type",
             title="Processing Time by Application Type", points=False)
fig.update_layout(showlegend=False)
fig.show()

**Business Interpretation.** Mortgages and Business Loans take noticeably
longer than Personal and Auto Loans — they carry more inherent underwriting
complexity (see `data/README.md`) and are more likely to be flagged for
additional review. This is expected and, importantly, is already reflected
in their more generous SLA targets — the SLA section below shows their
breach rates are *lower*, not higher, despite the longer absolute time.

In [8]:
pi["risk_band"] = pd.cut(pi["risk_score"], [0, 25, 50, 75, 100],
                          labels=["0-25 (low)", "25-50", "50-75", "75-100 (high)"])
fig = px.box(pi, x="risk_band", y="total_processing_time_hours",
             title="Processing Time by Risk Band", points=False)
fig.show()

**Business Interpretation.** Processing time rises steadily with risk score
— higher-risk applications require deeper review at Credit Assessment and
Risk Review specifically (both stages scale service time with risk_score).
This is a deliberate, defensible business rule: riskier applications should
take longer to underwrite properly. It also means risk_score will be one of
the strongest predictors in the SLA-breach model built later.

In [9]:
pi["loan_amount_band"] = pd.qcut(pi["loan_amount"], 5,
                                  labels=["Q1 (smallest)", "Q2", "Q3", "Q4", "Q5 (largest)"])
fig = px.box(pi, x="loan_amount_band", y="total_processing_time_hours",
             title="Processing Time by Loan Amount Quintile (within-type)", points=False)
fig.show()

**Business Interpretation.** The largest loans (top quintile) take longer —
they trigger the "large application" review surcharge at Risk Review and
Approval. This matches a common real-world lending control: bigger exposure
warrants a second look, at the cost of speed.

In [10]:
fig = px.box(pi, x="region", y="total_processing_time_hours", title="Processing Time by Region", points=False)
fig.show()

**Business Interpretation.** Processing time is broadly similar across
regions — there is no single region with a structurally slower process.
This is a useful negative finding: it tells management that any bottleneck
fix should be organized around *stages* (departments), not *regions*.

In [11]:
fig = px.box(pi, x="channel", y="total_processing_time_hours", title="Processing Time by Channel", points=False)
fig.show()

**Business Interpretation.** Digital channels (Online, Mobile App) skew
slightly slower — they have a higher missing-document rate, which drives
Document Validation rework. Improving the document-upload experience on
digital channels would likely have an outsized effect relative to a
branch-side intervention.

In [12]:
fig = px.box(pi, x="priority", y="total_processing_time_hours", title="Processing Time by Priority", points=False)
fig.show()

**Business Interpretation.** High-priority applications are processed
somewhat faster on average (they are queue-jumped ahead of standard
applications), but the effect is moderate, not dramatic — expedited handling
speeds up *waiting* time, not the underlying *service* time a complex
application still requires. This matters for the SLA section next: a tight
SLA target combined with only a moderate speedup can still produce a
meaningful breach rate for "priority" customers.

## SLA Performance

In [13]:
overall = compute_sla_breach_rate(pi)
print(f"Overall SLA breach rate: {overall.loc[0, 'sla_breach_rate']:.1%}")

by_segment = compute_sla_breach_rate(pi, group_by="customer_segment").sort_values("sla_breach_rate", ascending=False)
fig = px.bar(by_segment, x="customer_segment", y="sla_breach_rate", text_auto=".1%",
             title="SLA Breach Rate by Customer Segment")
fig.update_yaxes(tickformat=".0%")
fig.show()

Overall SLA breach rate: 22.2%


**Business Interpretation.** Breach rate differences across segments trace
back to priority mix and application complexity rather than the segment
label itself — Corporate and Premium customers get tighter SLA targets in
exchange for expedited handling, so a segment with more high-priority,
high-complexity applications will show a higher breach rate even though its
absolute processing time is often similar to or better than Retail's.

In [14]:
by_type = compute_sla_breach_rate(pi, group_by="application_type").sort_values("sla_breach_rate", ascending=False)
fig = px.bar(by_type, x="application_type", y="sla_breach_rate", text_auto=".1%",
             title="SLA Breach Rate by Application Type")
fig.update_yaxes(tickformat=".0%")
fig.show()

**Business Interpretation.** Personal Loans breach SLA most often despite
being the *fastest* product in absolute terms — their SLA target is the
tightest, calibrated for a high-volume, low-complexity product. Mortgages
breach least, because their generous SLA target already accounts for
lengthy underwriting. The lesson for management: SLA breach rate alone can
be misleading without also looking at absolute cycle time (previous
section) — a product can be "fast but non-compliant" or "slow but
compliant".

In [15]:
gap_hours = pi["total_processing_time_hours"] - pi["sla_target_hours"]
breached = pi.assign(sla_gap_hours=gap_hours)[pi["sla_breached"] == 1]

fig = px.histogram(breached, x="sla_gap_hours", nbins=60,
                    title="How Far Over SLA Do Breached Applications Run? (hours past target)")
fig.show()

**Business Interpretation.** Most breaches are moderate overruns (a few
days past target), but there is a real tail of severe breaches — these are
the cases most likely to involve rework loops or arrival during a
high-utilization period at Credit Assessment/Risk Review (see the
process-mining and bottleneck-detection notebooks for exactly where that
time is lost).

## Summary of Key Findings

- **Volume** follows a predictable weekly pattern (Monday/Friday peaks,
  near-zero on weekends) — this is the root cause of periodic queueing,
  not random variation.
- **Processing time** is right-skewed and increases with risk, complexity,
  loan size, and application type (Mortgage/Business Loan > Auto Loan >
  Personal Loan) — all by deliberate, documented business rules.
- **SLA breach rate is ~15-25% overall**, concentrated in the
  fastest-nominal-target product (Personal Loan) rather than the slowest
  product (Mortgage) — a reminder that SLA compliance and absolute speed
  are different questions.
- These patterns motivate the next notebook: process mining to see exactly
  *where in the process* the time is being spent, and bottleneck detection
  to rank stages by operational impact.